## Торговая стратегия на основе ARIMA

r = np.log(close).diff().dropna()  # stationary target

In [ ]:
from statsmodels.tsa.statespace.sarimax import SARIMAX

r = np.log(close).diff().dropna()  # посчитать лог-доходности 


In [ ]:
# Rolling ARIMA forecast (walk-forward, refit periodically) ====
p_grid = [0,1,2,3]
q_grid = [0,1,2]
min_train = 250         # ~1 trading year
refit_every = 20        # refit order/params every 20 steps

fcast = pd.Series(index=r.index, dtype=float)
best_order = None
model = None
last_refit = -10**9

def fit_best_arma(y):
    best_aic, best_res, best_order = np.inf, None, None
    for p in p_grid:
        for q in q_grid:
            if p == 0 and q == 0:
                continue
            try:
                res = SARIMAX(y, order=(p,0,q), enforce_stationarity=False,
                              enforce_invertibility=False).fit(disp=False)
                if res.aic < best_aic:
                    best_aic, best_res, best_order = res.aic, res, (p,0,q)
            except Exception:
                pass
    return best_res, best_order

for i in range(min_train, len(r)-1):
    # Refit model and (re)select order every refit_every steps
    if (i - last_refit) >= refit_every or model is None:
        model, best_order = fit_best_arma(r.iloc[:i])
        last_refit = i
    # 1-step-ahead forecast for t+1
    fc = model.get_forecast(steps=1).predicted_mean.iloc[0]
    fcast.iloc[i+1] = fc
    # Update model with the realized observation at t (fast filter update)
    try:
        model = SARIMAX(r.iloc[:i+1], order=best_order,
                        enforce_stationarity=False, enforce_invertibility=False
                       ).filter(model.params)
    except Exception:
        # if filtering fails, force full refit next loop
        model = None
        last_refit = -10**9

H:\conda\envs\py312\Lib\site-packages\statsmodels\tsa\base\tsa_model.py:473: ValueWarning:

A date index has been provided, but it has no associated frequency information and so will be ignored when e.g. forecasting.

H:\conda\envs\py312\Lib\site-packages\statsmodels\tsa\base\tsa_model.py:473: ValueWarning:

A date index has been provided, but it has no associated frequency information and so will be ignored when e.g. forecasting.

H:\conda\envs\py312\Lib\site-packages\statsmodels\tsa\base\tsa_model.py:473: ValueWarning:

A date index has been provided, but it has no associated frequency information and so will be ignored when e.g. forecasting.

H:\conda\envs\py312\Lib\site-packages\statsmodels\tsa\base\tsa_model.py:473: ValueWarning:

A date index has been provided, but it has no associated frequency information and so will be ignored when e.g. forecasting.

H:\conda\envs\py312\Lib\site-packages\statsmodels\tsa\base\tsa_model.py:473: ValueWarning:

A date index has been provided, but 

In [ ]:
# Align forecasts to the *next* bar (t+1)
fcast = fcast.dropna()
# Position at t uses forecast made at t-1; here fcast is already t-1 -> t
pos = (fcast > 0).astype(bool)

# Bring to price index (forward-fill between forecast dates)
pos = pos.reindex(close.index, method='ffill').fillna(False)

<positron-console-cell-35>:7: FutureWarning:

Downcasting object dtype arrays on .fillna, .ffill, .bfill is deprecated and will change in a future version. Call result.infer_objects(copy=False) instead. To opt-in to the future behavior, set `pd.set_option('future.no_silent_downcasting', True)`



In [ ]:
#Signals (long-in/cash-out) 
entries = pos & ~pos.shift(1, fill_value=False)
exits   = ~pos &  pos.shift(1, fill_value=False)

In [ ]:
# Backtest
pf = vbt.Portfolio.from_signals(
    close=close,
    entries=entries,
    exits=exits,
    init_cash=100,
    fees=0.0005,        # 5 bps each way (adjust to your venue)
    slippage=0.0005,
    freq='1D'
)

In [ ]:
pf.stats()

Start                               2007-07-20 00:00:00
End                                 2025-08-30 00:00:00
Period                               4577 days 00:00:00
Start Value                                       100.0
End Value                                     36.045665
Total Return [%]                             -63.954335
Benchmark Return [%]                          548.69351
Max Gross Exposure [%]                            100.0
Total Fees Paid                               70.949951
Max Drawdown [%]                              76.119436
Max Drawdown Duration                1965 days 00:00:00
Total Trades                                       1041
Total Closed Trades                                1040
Total Open Trades                                     1
Open Trade PnL                                -0.036055
Win Rate [%]                                  46.826923
Best Trade [%]                                63.647107
Worst Trade [%]                              -38

In [ ]:
pf.plot().show()        # equity & drawdowns


### Почему такие плохие результаты?

1. на дневном уровне доходности близки к белому шуму -> ARIMA пытается уловить микродвижения 
2. слишком много сделок (примерно 1 сделка раз в 4 дня). Издержки + слиппаж = отрицательное мат. ожидание
3. высокие транзакционные издержки 
4. 



In [ ]:
from pmdarima import arima

In [ ]:
min_train     = 252            # ~1Y warm-up
refit_every   = 60             # refit auto_arima every 60 bars
k             = 0.1           # signal threshold in σ units ( you can try 0.25 / 0.5)
max_p, max_q  = 3, 3           # search bounds (keep modest for speed)
stationary    = True           # we already use returns => d=0
seasonal      = False

In [ ]:
# Walk-forward: auto_arima + periodic refit + incremental update
close = price['adj_close'].astype(float).sort_index().dropna()
r = np.log(close).diff().dropna()                      # daily log-returns
vol = r.rolling(60).std().shift(1)                     # σ_t available at time t (no look-ahead)
r = r.loc[vol.index]
close = close.loc[vol.index]


fcast = pd.Series(index=r.index, dtype=float)

In [ ]:
model = None
last_refit = -10**9

In [ ]:
for i in range(min_train, len(r) - 1):
    # Refit & reselect order every refit_every steps
    if (i - last_refit) >= refit_every or model is None:
        y_train = r.iloc[:i]  # data available up to time t=i-1
        y_train = r.iloc[:i].reset_index(drop=True)
        model = arima.auto_arima(
            y=y_train,
            start_p=0, start_q=0, max_p=max_p, max_q=max_q,
            d=0 if stationary else None,
            seasonal=seasonal,
            information_criterion='aic',  # AIC for speed; can use 'bic'
            stepwise=True,                # much faster than full grid
            suppress_warnings=True,
            error_action='ignore',
            with_intercept=True
        )
        last_refit = i
    else:
        # Incrementally update model with the latest observed return r[i-1]
        # (pmdarima accepts scalar or array-like)
        model.update(r.iloc[i-1:i])

    # One-step-ahead forecast for t+1 using info up to t
    try:
        f = float(model.predict(n_periods=1)[0])
    except Exception:
        f = np.nan
    fcast.iloc[i+1] = f


IndexError: iloc cannot enlarge its target object

In [ ]:
# Align & clean
fcast = fcast.dropna()
thr = (k * vol).reindex(fcast.index)


#  Thresholded trading rule: long only when forecast > k·σ
pos = (fcast > thr)  # True at forecast timestamp; applies from that bar onward
pos = pos.reindex(close.index, method='ffill').fillna(False)

# (Optional) require signal persistence to reduce whipsaws:
pos = pos.rolling(2).max().astype(bool)

entries = pos & ~pos.shift(1, fill_value=False)
exits   = ~pos &  pos.shift(1, fill_value=False)

<positron-console-cell-47>:8: FutureWarning:

Downcasting object dtype arrays on .fillna, .ffill, .bfill is deprecated and will change in a future version. Call result.infer_objects(copy=False) instead. To opt-in to the future behavior, set `pd.set_option('future.no_silent_downcasting', True)`



In [ ]:
pf = vbt.Portfolio.from_signals(
    close=close,
    entries=entries,
    exits=exits,
    init_cash=100,
    fees=0.0005,        # 5 bps each way; tune to your venue
    slippage=0.0005,
    freq='1D'
)

In [ ]:
pf.stats()

Start                         2007-07-23 00:00:00
End                           2025-08-30 00:00:00
Period                         4576 days 00:00:00
Start Value                                 100.0
End Value                              121.022606
Total Return [%]                        21.022606
Benchmark Return [%]                   532.476173
Max Gross Exposure [%]                      100.0
Total Fees Paid                          0.531499
Max Drawdown [%]                          5.10505
Max Drawdown Duration          4257 days 00:00:00
Total Trades                                    5
Total Closed Trades                             5
Total Open Trades                               0
Open Trade PnL                                0.0
Win Rate [%]                                 40.0
Best Trade [%]                          25.134527
Worst Trade [%]                         -2.901005
Avg Winning Trade [%]                   14.568232
Avg Losing Trade [%]                    -2.389008


In [ ]:
pf.plot().show()


In [ ]:
fcast.describe()


count    4250.000000
mean       -0.000085
std         0.002959
min        -0.061010
25%         0.000000
50%         0.000000
75%         0.000000
max         0.058983
dtype: float64

In [ ]:
vol.describe()


count    4516.000000
mean        0.022739
std         0.014359
min         0.007299
25%         0.015102
50%         0.018582
75%         0.024218
max         0.102885
Name: adj_close, dtype: float64